In [10]:
pip install git+https://github.com/SebastianJanampa/DETRPose.git@inference_only


  Cloning https://github.com/SebastianJanampa/DETRPose.git (to revision inference_only) to /tmp/pip-req-build-i9sm_f5l
  Running command git clone --filter=blob:none --quiet https://github.com/SebastianJanampa/DETRPose.git /tmp/pip-req-build-i9sm_f5l
  Running command git checkout -b inference_only --track origin/inference_only
  Switched to a new branch 'inference_only'
  branch 'inference_only' set up to track 'origin/inference_only'.
  Resolved https://github.com/SebastianJanampa/DETRPose.git to commit da12e0cd29864b1d3a289c562c34d423371a4157
  Installing build dependencies ... done
  Getting requirements to build wheel ... done
  Preparing metadata (pyproject.toml) ... done


In [ ]:
from detrpose import DETR

# Initialization
model = DETR(model='detrpose_hgnetv2_l')

# Inference
# The webcam cannot be accessed in this environment (e.g., Google Colab).
# Please provide an image file path or a video file path as the source.
# For example, to process an image:
# model(source='path/to/your/image.jpg')
# To process a video:
# model(source='path/to/your/video.mp4')
# Original line (commented out):
# model(source=0) # inference on a webcam

### Step 1: Upload your video file

First, record a video with your phone and upload it to Colab. This process is very similar to uploading an image file.

In [11]:
from google.colab import files
import os

print("Please upload your video file:")
uploaded_video = files.upload()

video_file_path = None
for fn_video in uploaded_video.keys():
    print(f'User uploaded video "{fn_video}" with length {len(uploaded_video[fn_video])} bytes')
    video_file_path = fn_video

if video_file_path and os.path.exists(video_file_path):
    print(f'Video file {video_file_path} successfully uploaded and found.')
else:
    print('Error: Video file not uploaded or found.')

Please upload your video file:


Saving WhatsApp Video 2026-09-29 at 11.50.36 AM.mp4 to WhatsApp Video 2026-09-29 at 11.50.36 AM (1).mp4
User uploaded video "WhatsApp Video 2026-09-29 at 11.50.36 AM (1).mp4" with length 2006365 bytes
Video file WhatsApp Video 2026-09-29 at 11.50.36 AM (1).mp4 successfully uploaded and found.


### Step 2: Process the video and count people

Now that you have your video uploaded, we can use `opencv-python` to read the video frame by frame, apply the `DETR` model for detection, and count the number of detected people in each frame. We'll also save the processed video with annotations and the count.

_Note: Ensure the `model` object has been initialized in a previous cell (e.g., cell `GLwfIuoqvQqE`)._

In [12]:
import cv2
import numpy as np

if video_file_path is None:
    print("No video file uploaded. Please upload a video first.")
else:
    # Open the video file
    cap = cv2.VideoCapture(video_file_path)

    if not cap.isOpened():
        print(f"Error: Could not open video file '{video_file_path}'.")
        print("Possible reasons:")
        print("1. The video file might be corrupted or incomplete.")
        print("2. The video codec is not supported by OpenCV in this environment.")
        print("   Please try converting your video to a common format like MP4 (H.264 codec) and re-uploading.")
        print("3. There might be an issue with file permissions (less likely in Colab).")
    else:
        # Get video properties
        fps = cap.get(cv2.CAP_PROP_FPS)
        width = int(cap.get(cv2.CAP_PROP_FRAME_WIDTH))
        height = int(cap.get(cv2.CAP_PROP_FRAME_HEIGHT))
        fourcc = cv2.VideoWriter_fourcc(*'mp4v') # Codec for .mp4
        output_filename = 'output_video_with_detections.mp4'
        out = cv2.VideoWriter(output_filename, fourcc, fps, (width, height))

        frame_count = 0
        all_people_counts = [] # List to store people count for each frame

        print(f"Processing video: {video_file_path}")
        print(f"Output video will be saved as: {output_filename}")

        while True:
            ret, frame = cap.read()
            if not ret:
                break

            frame_count += 1
            # Convert frame from BGR to RGB (DETR expects RGB)
            rgb_frame = cv2.cvtColor(frame, cv2.COLOR_BGR2RGB)

            # Perform inference
            results_video = model(source=rgb_frame)

            people_count = 0
            if 'scores' in results_video:
                # Assuming label '1' corresponds to 'person' based on previous output
                # Using a confidence threshold of 0.5
                people_count = len([score for label, score in zip(results_video['labels'], results_video['scores']) if label == 1 and score > 0.5])

            all_people_counts.append(people_count) # Store the count for this frame

            # Annotate the frame with the count
            annotated_frame = results_video.get('annotated_image', rgb_frame) # Use annotated if available, else original
            annotated_frame_bgr = cv2.cvtColor(annotated_frame, cv2.COLOR_RGB2BGR) # Convert back to BGR for OpenCV writing

            text = f"People: {people_count}"
            cv2.putText(annotated_frame_bgr, text, (50, 50), cv2.FONT_HERSHEY_SIMPLEX, 1.5, (0, 255, 0), 3, cv2.LINE_AA)

            # Write the frame to the output video
            out.write(annotated_frame_bgr)

            # Removed: if frame_count % 30 == 0: # Print update every 30 frames
            # Removed:     print(f"Processed frame {frame_count}. Detected {people_count} people.")

        cap.release()
        out.release()
        print(f"Video processing complete. Output saved to {output_filename}")

        # --- New: Summarize people counts ---
        if all_people_counts:
            max_people = max(all_people_counts)
            avg_people = sum(all_people_counts) / len(all_people_counts)
            print(f"\nSummary of People Detection:")
            print(f"- Maximum number of people detected at once: {max_people}")
            print(f"- Average number of people detected per frame: {avg_people:.2f}")
        else:
            print("No people were detected in the video.")
        # --- End of New Summary ---

        # Optional: Display the first frame of the output video or a message to download
        from IPython.display import HTML
        from base64 import b64encode
        video_bytes = open(output_filename, 'rb').read()
        encoded_video = b64encode(video_bytes).decode()
        display(HTML(f"""
        <video width='{width}' controls>
            <source src='data:video/mp4;base64,{encoded_video}' type='video/mp4'>
            Your browser does not support the video tag.
        </video>
        <p>You can download the processed video: <a href='{output_filename}' download>Download {output_filename}</a></p>
        """))

Processing video: WhatsApp Video 2026-09-29 at 11.50.36 AM (1).mp4
Output video will be saved as: output_video_with_detections.mp4
Video processing complete. Output saved to output_video_with_detections.mp4

Summary of People Detection:
- Maximum number of people detected at once: 9
- Average number of people detected per frame: 3.36
